# Laplacian Smoothing and Mesh Dual

This notebook contains an exercise where you 
- smooth a mesh by replacing each vertex with the average of its neighbors. 
- compute the volume of a tetrahedral mesh
- compute the dual of a mesh by converting each vertex to a face such that the vertices of the new face correspond to the faces of the old mesh.

In [1]:
from pygel3d import hmesh, jupyter_display as jd
from numpy import zeros
from numpy.linalg import det
jd.set_export_mode(True)
def mesh_stats(m):
    print("# faces : ", m.no_allocated_faces(), " # vertices : ", m.no_allocated_vertices())

### Problem 1: Insert code to complete the smoothing function 

In [2]:
def smooth(m, max_iter=1):
    pos = m.positions()
    new_pos = zeros(pos.shape)
    for iter in range(0,max_iter):
        # For each vertex, we find it's neighbours
        for v in m.vertices():
            neighs = m.circulate_vertex(v, mode = 'v') # Finding neighsbor
            coord_sum = 0 # Setting up variables to hold valeus
            counter = 0
            for n_idx in neighs:
                coord_sum += pos[n_idx] # sum the coordinates
                counter += 1 # add 1 to the neighbour counter

            new_pos[v] = coord_sum/counter # Assign the same index in new_pos, with the average value

        pos[:] = new_pos # After looping over all vertices, reassign pos to new_pos, so we can iteratively smooth
    return pos

### Problem 2: Insert code to compute the volume of a triangle mesh

In [3]:
def calculate_volume(m):
    pos = m.positions()
    vol = 0
    # For simplicity we choose the connecting point to create the tetrahedron as [0, 0, 0]
    for f in m.faces(): # Loop over all faces in the mesh
        # Extracting the vertices for each face
        vs = m.circulate_face(f, mode = 'v')

        vol += (1/6) * det(pos[vs])
        

    return vol            

### Problem 3: Insert code to complete the dual function

In [12]:
import numpy as np
from pygel3d import hmesh

def compute_dual_mesh(m: hmesh.Manifold) -> hmesh.Manifold:
    dual = hmesh.Manifold()

    # 1. Precompute the center of mass (centroid) for each original face
    face_centroids = {}
    for f in m.faces():
        # circulate_face(f, mode='v') returns incident vertices of face f
        f_verts = list(m.circulate_face(f, mode='v'))
        coords = [m.positions()[v] for v in f_verts]
        face_centroids[f] = np.mean(coords, axis=0)

    # 2. Each primal vertex becomes a dual polygon
    for v in m.vertices():
        # Optional: skip boundary vertices if your mesh is open/has holes
        # (dual faces around boundary vertices are open fans, not closed polygons)
        # In GEL, an invalid face index (often -1 or 2^32-1) indicates a boundary.
        incident_faces = list(m.circulate_vertex(v, mode='f'))
        
        # Filter out boundary halfedges / invalid face handles
        valid_faces = [f for f in incident_faces if f in face_centroids]
        
        # A valid closed face needs at least 3 vertices
        if len(valid_faces) >= 3:
            # The face centroids are already in counterclockwise order
            poly_points = [face_centroids[f] for f in valid_faces]
            dual.add_face(poly_points)

    return dual

### Show original mesh
If you don't see anything it is probably a problem with the path to `data/bunnygtest.obj`. The path should be relative to the current working directory: probably this is the directory that Jupyter Notebook shows when it starts.

In [5]:
m = hmesh.load("bunnygtest.obj")
mesh_stats(m)
print("Volume: ", calculate_volume(m))
jd.display(m)

# faces :  6966  # vertices :  3485
Volume:  0.0007541261586712996


### Show the smoothed mesh

In [6]:
m_s = hmesh.Manifold(m)
smooth(m_s,50)
print("Volume: ", calculate_volume(m_s))
jd.display(m_s)

Volume:  0.0004567991015581805


### Show the dual mesh

In [13]:
mesh_stats(m)
m_d = compute_dual_mesh(m)
mesh_stats(m_d)
jd.display(m_d)

# faces :  6966  # vertices :  3485
# faces :  3485  # vertices :  20898


When everything works, export this to an HTML file and submit that!